# [REPERTOIRE DES ENTREPRISES](https://ge.ch/sitg/fiche/2099)
### Importation des modules

In [1]:
import numpy as np
import os
import pandas as pd 
import plotly.express as px
from plotly.offline import plot
import shutil
import ssl
from Swisstopo import SwisstopoConverter as sw
import wget

### Configurations

In [2]:
ssl._create_default_https_context = ssl._create_unverified_context
pd.set_option('display.max_columns', None)

In [3]:
url = 'https://ge.ch/sitg/geodata/SITG/OPENDATA/REG_ENTREPRISE_ETABLISSEMENT-CSV.zip'

zip = url.split('/')[-1] # prend les caractères après le dernier /
folder = zip.split('.')[0] # prend les caractères avant le .

wget.download(url, zip) # telecharge
shutil.unpack_archive(zip, folder) # dé-zip

file_name = [f for f in os.listdir(folder) if f.endswith('.csv')][0] # nom du premier csv dans le folder
path = f"{folder}/{file_name}"

types = {'TEL_PRINCIPAL': object}

df = pd.read_csv(path, sep= ';', low_memory=False, dtype=types)

os.remove(zip)
shutil.rmtree(folder)

df.head()

,OBJECTID,TYPE_REG,ID_ETABLISSEMENT,NOM,UNITE_LOCALE,COMPLEMENT_LOCALI,STATUT_REG,IMMAT_DT,TYPE_LOCAL,CODE_NOGA,BRANCHE,ACTIVITE_DETAIL,TAILLE,RAISON_SOC_PARENT,ID_ENTREPRISE,TEL_PRINCIPAL,TEL_SECONDAIRE,FAX,EMAIL,SITE_INTERNET,PHYS_RUE,PHYS_NUMRUE,PHYS_NPA,PHYS_LOCALITE,PHYS_COMMUNE,IDPADR,ADRESSE,NUM_IDE,RAISON_SOCIALE,NATURE_JURID,SIEGE_CANTON,SIEGE_PAYS,SOUS_TYPE,E,N
0,64,Etablissement,1-4XH-90873,Bureaux Unifund,53430786.0,NaN,En activité,2014-05-08,Bureau/étude/cabinet,661900,Autres activités auxiliaires de services finan...,NaN,10-19 travailleurs,Unifund SA,1-4XH-90872,NaN,NaN,NaN,NaN,NaN,Rue du Rhône,30,1204,Genève,Genève,930225024521,Rue du Rhône 30,NaN,Bureaux Unifund,NaN,NaN,NaN,NaN,2500216.06,1117824.96
1,65,Etablissement,1-4XH-90876,Poste de Plan-les-Ouates,53712202.0,NaN,En activité,1983-07-26,Bureau/étude/cabinet,531000,Activités de poste dans le cadre d'une obligat...,NaN,3-5 travailleurs,Poste CH Réseau SA,1-2CYYS1,+41228800434,4.184889e+10,NaN,NaN,https://www.post.ch/,Place des Aviateurs,1,1228,Plan-les-Ouates,Plan-les-Ouates,940829153512,Place des Aviateurs 1,NaN,Poste de Plan-les-Ouates,NaN,NaN,NaN,NaN,2498254.90,1113899.10
2,66,Etablissement,1-4XH-90877,Poste de Puplinge,53712239.0,NaN,En activité,1983-07-27,Bureau/étude/cabinet,531000,Activités de poste dans le cadre d'une obligat...,NaN,1-2 travailleurs,Poste CH Réseau SA,1-2CYYS1,+41223497392,NaN,NaN,NaN,https://www.post.ch/,Rue de Fremis,24,1241,Puplinge,Puplinge,930225034872,Rue de Fremis 24,NaN,Poste de Puplinge,NaN,NaN,NaN,NaN,2506813.70,1118406.28
3,67,Etablissement,1-4XH-90878,Poste de Thônex,66914041.0,Centre commercial de Thônex,En activité,1983-07-27,Bureau/étude/cabinet,531000,Activités de poste dans le cadre d'une obligat...,NaN,10-19 travailleurs,Poste CH Réseau SA,1-2CYYS1,+41848888888,NaN,NaN,NaN,https://www.post.ch/,Rue de Genève,106,1226,Thônex,Thônex,50221144636,Rue de Genève 106,NaN,Poste de Thônex,NaN,NaN,NaN,NaN,2504511.41,1116473.34
4,68,Etablissement,1-4XH-90879,Poste de Eaux-Vives 6,66914099.0,NaN,En activité,1983-07-08,Bureau/étude/cabinet,531000,Activités de poste dans le cadre d'une obligat...,NaN,10-19 travailleurs,Poste CH Réseau SA,1-2CYYS1,+41848888888,NaN,NaN,NaN,https://www.post.ch/,Rue du 31-Décembre,47,1207,Genève,Genève,930325144634,Rue du 31-Décembre 47,NaN,Poste de Eaux-Vives 6,NaN,NaN,NaN,NaN,2501403.20,1117573.01


In [4]:
df = df.sort_values(by='TYPE_LOCAL', ascending=False).drop_duplicates(subset='ID_ENTREPRISE', keep='first')

df = df.drop_duplicates(subset=['NOM'])

#df['Division'] = (df['CODE_NOGA'] / 10000).astype(int)
#df['Groupe'] = (df['CODE_NOGA'] / 1000).astype(int)
#df['Classe'] = (df['CODE_NOGA'] / 100).astype(int)
#df['Genre'] = (df['CODE_NOGA'] / 10).astype(int)

df['EMPLACEMENT'] = [f'{x.PHYS_RUE} {x.PHYS_NUMRUE}, {x.PHYS_NPA} {x.PHYS_LOCALITE}' for _, x in df.iterrows()]

df[['latitude', 'longitude']] = df.apply(lambda row: pd.Series(sw.from_mn95_to_wgs(east=row['E'], north=row['N'])), axis=1)

df["TAILLE"] = (
    df["TAILLE"]
    .replace("Sans travailleur", "Indépendant")
    .fillna("Indépendant")
)

df["TYPE_LOCAL"] = df["TYPE_LOCAL"].fillna("Non précisé")
df["IMMAT_YEAR"] = pd.to_datetime(df["IMMAT_DT"]).dt.year

In [5]:
# Définir les conditions pour chaque plage de valeurs et leurs correspondances aux définitions
conditions = [
    (df['CODE_NOGA'] >= 11100) & (df['CODE_NOGA'] <= 32200),
    (df['CODE_NOGA'] >= 51000) & (df['CODE_NOGA'] <= 99000),
    (df['CODE_NOGA'] >= 101100) & (df['CODE_NOGA'] <= 332000),
    (df['CODE_NOGA'] >= 351100) & (df['CODE_NOGA'] <= 353000),
    (df['CODE_NOGA'] >= 360000) & (df['CODE_NOGA'] <= 390000),
    (df['CODE_NOGA'] >= 411000) & (df['CODE_NOGA'] <= 439905),
    (df['CODE_NOGA'] >= 451101) & (df['CODE_NOGA'] <= 479900),
    (df['CODE_NOGA'] >= 491000) & (df['CODE_NOGA'] <= 532000),
    (df['CODE_NOGA'] >= 551001) & (df['CODE_NOGA'] <= 563002),
    (df['CODE_NOGA'] >= 581100) & (df['CODE_NOGA'] <= 639900),
    (df['CODE_NOGA'] >= 641100) & (df['CODE_NOGA'] <= 663002),
    (df['CODE_NOGA'] >= 681000) & (df['CODE_NOGA'] <= 683200),
    (df['CODE_NOGA'] >= 691001) & (df['CODE_NOGA'] <= 750000),
    (df['CODE_NOGA'] >= 771100) & (df['CODE_NOGA'] <= 829900),
    (df['CODE_NOGA'] >= 841100) & (df['CODE_NOGA'] <= 843000),
    (df['CODE_NOGA'] >= 851000) & (df['CODE_NOGA'] <= 856000),
    (df['CODE_NOGA'] >= 861001) & (df['CODE_NOGA'] <= 889902),
    (df['CODE_NOGA'] >= 900101) & (df['CODE_NOGA'] <= 932900),
    (df['CODE_NOGA'] >= 941100) & (df['CODE_NOGA'] <= 960900),
    (df['CODE_NOGA'] >= 970000) & (df['CODE_NOGA'] <= 982000),
    (df['CODE_NOGA'] >= 990001) & (df['CODE_NOGA'] <= 990003),
]

choices =  ['Agriculture, sylviculture et pêche',
            'Industries extractives',
            'Industrie manufacturière',
            "Production et distribution d'électricité, de gaz, de vapeur et d'air conditionné",
            "Production et distribution d'eau; assainissement, gestion des déchets et depollution",
            'Construction',
            "Commerce; réparation d'automobiles et de motocycles",
            'Transports et entreposage',
            'Hébergement et restauration',
            'Information et communication',
            "Activités financières et d'assurance",
            'Activités immobilières',
            'Activités spécialisées, scientifiques et techniques',
            'Activités de services administratifs et de soutien',
            'Administration publique',
            'Enseignement',
            'Santé humaine et action sociale',
            'Arts, spectacles et activités récréatives',
            'Autres activités de services',
            "Activités des ménages en tant qu'employeurs; activités indifférenciées des ménages en tant que producteurs de biens et services pour usage propre",
            'Activités extra‐territoriales']

# Appliquer les conditions et les correspondances aux définitions
df['DEFINITION_NOGA'] = np.select(conditions, choices, default='Autre')

In [6]:
df.to_csv('reg.csv')

In [7]:
fig = px.scatter_map(
    df,
    lat="latitude",
    lon="longitude",
    hover_name="NOM",
    hover_data=["BRANCHE", "SITE_INTERNET"],
    center=dict(lat=46.2043, lon=6.1431),
    zoom=11,
    map_style="carto-positron"
)

fig.update_layout(
    margin={"r": 0, "t": 0, "l": 0, "b": 0},
    title={
        "text": "Genève Entreprises",
        "x": 0.1,
        "y": 0.95
    }
)

fig.show()

plot(fig, filename="map.html")

'map.html'

In [8]:
fig = px.density_map(
    df,
    lat="latitude",
    lon="longitude",
    radius=5,
    center=dict(lat=46.2043, lon=6.1431),
    zoom=11,
    map_style="open-street-map"
)

fig.update_layout(
    margin={"r": 0, "t": 0, "l": 0, "b": 0},
    title={
        "text": "Densité exploratoire",
        "x": 0.1,
        "y": 0.95
    }
)

fig.show()

In [9]:
shutil.rmtree('__pycache__')